# Data Preprocessing and KB Construction

This notebook covers the data cleaning, embedding and vectorization to construct the the knowledge base with the exchange data.

In [1]:
# Import the required packages
import json
import re
import hashlib
from pathlib import Path

import pandas as pd

In [20]:
# Import the required packages
import json
import re
import hashlib
from pathlib import Path
import pandas as pd

## Load the collected documents

In [2]:
# Set the file paths for the various exchange documents
TEXT_FILES = {
    "jse_disclosures": Path("jse_corpus.json"),
    "jse_annual_reports_local": Path("jse_local_pdf_corpus.json"),
    "bse_disclosures": Path("bse_corpus.json"),
    "bse_financials_local": Path("bse_local_pdf_corpus.json"),
    "ttse_general_local": Path("ttse_local_pdf_corpus.json"),}

STRUCTURED_FILES = {
    "jse_price": Path("jse_price_data.csv"),
    "bse_price": Path("bse_price_data.csv"),
    "ttse_bonds": Path("ttse_bond_data.csv"),
    "ttse_divs_market_summary": Path("ttse_market_summary.csv"),
    "ttse_divs_sector_detail": Path("ttse_sector_detail.csv"),
    "ttse_ds_market_summary": Path("ttse_daily_quotes_market_summary.csv"),
    "ttse_ds_security_detail": Path("ttse_daily_quotes_security_detail.csv"),}

In [3]:
# Load normalize the text into one schema and save the metadata for each document
def normalize_record(raw: dict, source_key: str, default_exchange: str) -> dict:
    exchange = raw.get("exchange") or raw.get("source") or default_exchange
    if exchange not in ("jse", "bse", "ttse"):
        exchange = default_exchange
    if "annual" in source_key or "financials" in source_key:
        doc_type = "annual_report_or_financials"
    elif "disclosures" in source_key:
        doc_type = "disclosure"
    elif "general" in source_key:
        doc_type = "general_document"
    else:
        doc_type = "unknown"
    title = raw.get("title") or raw.get("filename") or raw.get("company_name") or ""
    date = raw.get("date") or raw.get("year") or None
    company = raw.get("company_name") or raw.get("instrument_code") or None
    url = raw.get("url") or raw.get("filepath") or raw.get("source_post_url") or ""
    text = raw.get("text", "")
    retrieved_via = raw.get("retrieved_via", "unknown")
    raw_id = raw.get("id") or f"{exchange}-{source_key}-{hashlib.md5(url.encode()).hexdigest()[:10]}"
    return {
        "id": raw_id, "exchange": exchange, "doc_type": doc_type, "title": title, "date": date,
        "company": company, "url": url, "text": text, "retrieved_via": retrieved_via,
        "source_file": source_key,}

# Exclude any trade reports
EXCLUDED_TITLE_PATTERNS = ["trading report package"]

def is_excluded_title(title: str) -> bool:
    title_lower = (title or "").lower()
    return any(p in title_lower for p in EXCLUDED_TITLE_PATTERNS)

# Load in all text records except the trade reports
all_text_records = []
excluded_count = 0
for source_key, path in TEXT_FILES.items():
    if not path.exists():
        continue
    default_exchange = source_key.split("_")[0]
    with open(path, "r", encoding="utf-8") as f:
        raw_records = json.load(f)
    for raw in raw_records:
        if is_excluded_title(raw.get("title", "")):
            excluded_count += 1
            continue
        all_text_records.append(normalize_record(raw, source_key, default_exchange))
    print(f"{source_key}: loaded {len(raw_records)} records")

# Print the total number of records loaded
print(f"Total text records loaded (before cleaning/dedup): {len(all_text_records)}")

jse_disclosures: loaded 5531 records
jse_annual_reports_local: loaded 3287 records
bse_disclosures: loaded 604 records
bse_financials_local: loaded 148 records
ttse_general_local: loaded 1305 records
Total text records loaded (before cleaning/dedup): 9884


## Clean text and remove duplicates

In [4]:
# Describes the page number pattern to remove
PAGE_NUMBER_PATTERN = re.compile(r"^\s*(page\s+)?\d{1,4}\s*(of\s+\d{1,4})?\s*$", re.IGNORECASE)

# Remove the page numbers from the text
def clean_text(text: str) -> str:
    if not text:
        return ""
    lines = text.split("\n")
    cleaned_lines = []
    for line in lines:
        stripped = line.strip()
        if not stripped or PAGE_NUMBER_PATTERN.match(stripped):
            continue
        cleaned_lines.append(stripped)
    cleaned = "\n".join(cleaned_lines)
    cleaned = re.sub(r"[ \t]{2,}", " ", cleaned)
    cleaned = re.sub(r"\n{3,}", "\n\n", cleaned)
    cleaned = "".join(c for c in cleaned if c.isprintable() or c in "\n\t")
    return cleaned.strip()

# Apply the cleaning function to every record in the corpus
for r in all_text_records:
    r["text"] = clean_text(r["text"])
    r["char_length"] = len(r["text"])

# Print the cleaning results as a sanity check
empty_after_cleaning = sum(1 for r in all_text_records if r["char_length"] == 0)
print(f"Records with empty text after cleaning: {empty_after_cleaning}")
print(f"Average char length: {sum(r['char_length'] for r in all_text_records) / max(len(all_text_records), 1):.0f}")

Records with empty text after cleaning: 153
Average char length: 14212


In [5]:
# Define function to normalize text by removing whitespace and set to lowercase before hashing
def content_hash(text: str) -> str:
    return hashlib.md5(text.strip().lower().encode("utf-8")).hexdigest()

seen_hashes = {}
deduped_records = []
duplicates_found = []

# Check for any duplicates and remove any duplicated text
for r in all_text_records:
    if not r["text"]:
        continue
    h = content_hash(r["text"])
    if h in seen_hashes:
        duplicates_found.append((r["id"], seen_hashes[h]))
        continue
    seen_hashes[h] = r["id"]
    deduped_records.append(r)

# Print the results for the removal of duplications
print(f"Records before dedup (excluding empty): {len(all_text_records) - empty_after_cleaning}")
print(f"Duplicates removed: {len(duplicates_found)}")
print(f"Final deduplicated record count: {len(deduped_records)}")

Records before dedup (excluding empty): 9731
Duplicates removed: 128
Final deduplicated record count: 9603


In [6]:
# Save the final, cleaned, deduplicated corpus
out_path = Path("unified_text_corpus.json")
out_path.write_text(json.dumps(deduped_records, indent = 2, ensure_ascii = False), encoding = "utf-8")
print(f"Saved {len(deduped_records)} records to {out_path.resolve()}")

# Load the corpus back into a DataFrame for reporting and sanity checks
df = pd.DataFrame(deduped_records)

# Print the number of records by type and exchange
print("\nBreakdown by exchange + doc_type:")
print(df.groupby(["exchange", "doc_type"]).size())

# Print number of records by retrieval method
print("\nBreakdown by retrieved_via:")
print(df["retrieved_via"].value_counts())

Saved 9603 records to /home/areas001/Final Project/Final Notebooks/unified_text_corpus.json

Breakdown by exchange + doc_type:
exchange  doc_type                   
bse       annual_report_or_financials     133
          disclosure                      106
jse       annual_report_or_financials    3244
          disclosure                     4972
ttse      general_document               1148
dtype: int64

Breakdown by retrieved_via:
retrieved_via
wp_api       5078
direct       3894
cloud_ocr     631
Name: count, dtype: int64


## Perform a sanity check on OCR documents

In [21]:
# Load the OCR documents
ocr_records = df[df["retrieved_via"].isin(["ocr", "cloud_ocr"])]

# Print the number of OCR documents
print(f"{len(ocr_records)} OCR records.")

# Print a sample of the OCR documents for review
sample = ocr_records.sample(min(5, len(ocr_records)), random_state = 42) if len(ocr_records) else ocr_records
for _, row in sample.iterrows():
    print(f"\n--- {row['exchange'].upper()} | {row['title']} ({row['retrieved_via']}) ---")
    print(row["text"][:400])

631 OCR records.

--- TTSE | Medcorp Limited - Notice of Resignation of Director (Press Release) dd 13.05.2026.pdf (cloud_ocr) ---
MEDCORP LIMITED
(the "Company")
NOTICE OF MATERIAL CHANGE
Pursuant to section 64(1)(b) of the Securities Act, 2012
and the Trinidad and Tobago Stock Exchange Rules
The Company advises that Mr. Gerrard Lee - Inniss
resigned as an Independent Director effective 11th May
2026.
Mrs. Wendy Maharaj - Singh
Corporate Secretaru
17th May 2026
MEDCORP LIMITED

--- JSE | Unaudited-Financials-ended-June-30-2026.pdf (cloud_ocr) ---
REPORT OF THE BOARD OF DIRECTORS
CONSOLIDATED UNAUDITED FINANCIAL STATEMENTS
FOR QUARTER ENDED JUNE 30, 2026
SECOND QUARTER FINANCIAL HIGHLIGHTS
Description
Q2 2026
Q2 2025
Change
%
Total
$721.9m
$658.5m
9.6
Income
Total
$531m
$607.9m
Expenses
Net Profit
$132.4m
$45.5m
12.7
After Tax
YTD
YTD
$1,432.5m
$1,519.6m
$1,050.7m
$266.9m
$1,162 m
$281.8m
Change
%
-5.7
9.6
-5.3
Earnings Per
Share
Return
on


--- JSE | Post-Meeting-Notice-SREXF-Result-o

## Trade Data Cleaning

In [9]:
# Define a function to normalize the trade data column names, lowercase, strip whitespace
def clean_structured_df(df_in: pd.DataFrame) -> pd.DataFrame:
    df_in = df_in.copy()
    new_columns = [re.sub(r"\s+", "_", str(c).strip().lower()) for c in df_in.columns]
    
    seen = {}
    deduped_columns = []
    for col in new_columns:
        if col in seen:
            seen[col] += 1
            deduped_columns.append(f"{col}_{seen[col]}")
        else:
            seen[col] = 0
            deduped_columns.append(col)
    df_in.columns = deduped_columns

    # Strip leading/trailing whitespace from the column names
    for col in df_in.select_dtypes(include = "object").columns:
        df_in[col] = df_in[col].astype(str).str.strip()
    df_in = df_in.replace("", pd.NA)
    df_in = df_in.dropna(how="all")
    return df_in

# Create variable to save the cleaned trade data
cleaned_structured = {}

# Save the clean trade data
for name, path in STRUCTURED_FILES.items():
    if not path.exists():
        continue
    raw_df = pd.read_csv(path)
    cleaned_df = clean_structured_df(raw_df)
    cleaned_structured[name] = cleaned_df
    out_path = Path(f"cleaned_{path.name}")
    cleaned_df.to_csv(out_path, index = False)

    # Print the file names and the number of rows
    print(f"{name}: {len(raw_df)} -> {len(cleaned_df)} rows after cleaning, saved to {out_path}")

jse_price: 69506 -> 69506 rows after cleaning, saved to cleaned_jse_price_data.csv
bse_price: 25046 -> 25046 rows after cleaning, saved to cleaned_bse_price_data.csv
ttse_bonds: 8165 -> 8165 rows after cleaning, saved to cleaned_ttse_bond_data.csv
ttse_divs_market_summary: 2970 -> 2970 rows after cleaning, saved to cleaned_ttse_market_summary.csv
ttse_divs_sector_detail: 30829 -> 30829 rows after cleaning, saved to cleaned_ttse_sector_detail.csv
ttse_ds_market_summary: 4952 -> 4952 rows after cleaning, saved to cleaned_ttse_daily_quotes_market_summary.csv
ttse_ds_security_detail: 16041 -> 16041 rows after cleaning, saved to cleaned_ttse_daily_quotes_security_detail.csv


In [10]:
# Print a summary of the text corpus
print("=== TEXT CORPUS ===")
print(f"Total records: {len(deduped_records)}")
print(df.groupby("exchange").size())
print("\n=== STRUCTURED DATA ===")

for name, cdf in cleaned_structured.items():
    print(f"{name}: {len(cdf)} rows, {len(cdf.columns)} columns")

=== TEXT CORPUS ===
Total records: 9603
exchange
bse      239
jse     8216
ttse    1148
dtype: int64

=== STRUCTURED DATA ===
jse_price: 69506 rows, 16 columns
bse_price: 25046 rows, 13 columns
ttse_bonds: 8165 rows, 15 columns
ttse_divs_market_summary: 2970 rows, 12 columns
ttse_divs_sector_detail: 30829 rows, 13 columns
ttse_ds_market_summary: 4952 rows, 9 columns
ttse_ds_security_detail: 16041 rows, 16 columns


---
## Chunking

In [11]:
# Import the required packages
from transformers import AutoTokenizer

# Set the chunk size and overlap
CHUNK_SIZE_TOKENS = 512
CHUNK_OVERLAP_TOKENS = 100

# Load in BGE-M3 tokenizer
tokenizer = AutoTokenizer.from_pretrained("BAAI/bge-m3")

# Define function to count the token
def count_tokens(text: str) -> int:
    return len(tokenizer.encode(text, add_special_tokens = False))

# Define function to spilt the text into sentences
def split_into_sentences(text: str) -> list:
    text = text.replace("\n", " ")
    sentences = re.split(r"(?<=[.!?])\s+(?=[A-Z0-9])", text)
    return [s.strip() for s in sentences if s.strip()]

# Define the recursive character split function
def recursive_char_split(text: str, max_tokens: int) -> list:
    if count_tokens(text) <= max_tokens:
        return [text]
    for sep in ["\n\n", "\n", ". ", " "]:
        if sep in text:
            parts = text.split(sep)
            chunks, current = [], ""
            for part in parts:
                candidate = (current + sep + part) if current else part
                if count_tokens(candidate) <= max_tokens:
                    current = candidate
                else:
                    if current:
                        chunks.append(current)
                    current = part
            if current:
                chunks.append(current)
            final = []
            for c in chunks:
                final.extend(recursive_char_split(c, max_tokens) if count_tokens(c) > max_tokens else [c])
            return final
    approx_chars_per_token = 4
    cut = max_tokens * approx_chars_per_token
    return [text[i:i+cut] for i in range(0, len(text), cut)]

# Define the chunking function
def chunk_document(text: str, chunk_size: int = CHUNK_SIZE_TOKENS, overlap: int = CHUNK_OVERLAP_TOKENS) -> list:
    sentences = split_into_sentences(text)
    if not sentences:
        return []
    chunks, current_sentences, current_tokens = [], [], 0
    for sentence in sentences:
        sentence_tokens = count_tokens(sentence)
        if sentence_tokens > chunk_size:
            if current_sentences:
                chunks.append(" ".join(current_sentences))
                current_sentences, current_tokens = [], 0
            chunks.extend(recursive_char_split(sentence, chunk_size))
            continue
        if current_tokens + sentence_tokens > chunk_size:
            chunks.append(" ".join(current_sentences))
            overlap_sentences, overlap_tokens = [], 0
            for s in reversed(current_sentences):
                t = count_tokens(s)
                if overlap_tokens + t > overlap:
                    break
                overlap_sentences.insert(0, s)
                overlap_tokens += t
            current_sentences = overlap_sentences + [sentence]
            current_tokens = overlap_tokens + sentence_tokens
        else:
            current_sentences.append(sentence)
            current_tokens += sentence_tokens
    if current_sentences:
        chunks.append(" ".join(current_sentences))
    return chunks

In [13]:
# Chunk all the documents in the corpus
all_chunks = []
for doc in deduped_records:
    doc_chunks = chunk_document(doc["text"])
    for i, chunk_text in enumerate(doc_chunks):
        all_chunks.append({
            "chunk_id": f"{doc['id']}-chunk{i}", "doc_id": doc["id"], "exchange": doc["exchange"],
            "doc_type": doc["doc_type"], "title": doc["title"], "date": doc["date"],
            "company": doc["company"], "url": doc["url"], "retrieved_via": doc["retrieved_via"],
            "chunk_index": i, "text": chunk_text, "token_count": count_tokens(chunk_text),})

# Print the number of chunks
print(f"Total chunks created: {len(all_chunks)}")
print(f"Average tokens per chunk: {sum(c['token_count'] for c in all_chunks) / max(len(all_chunks), 1):.0f}")

# Save the chunks to a json file
chunks_out_path = Path("corpus_chunks.json")
chunks_out_path.write_text(json.dumps(all_chunks, indent = 2, ensure_ascii = False), encoding = "utf-8")
print(f"Saved to {chunks_out_path.resolve()}")

Token indices sequence length is longer than the specified maximum sequence length for this model (8560 > 8192). Running this sequence through the model will result in indexing errors


Total chunks created: 93139
Average tokens per chunk: 402
Saved to /home/areas001/Final Project/Final Notebooks/corpus_chunks.json


## Generate the dense + sparse embeddings

## 15. Load BGE-M3 and test dense + sparse output on a small batch

In [22]:
# Import the required packages
from FlagEmbedding import BGEM3FlagModel

# Load in the BGE-M3 embedding model
embed_model = BGEM3FlagModel("BAAI/bge-m3", use_fp16 = True)

Fetching 30 files:   0%|          | 0/30 [00:00<?, ?it/s]

/home/areas001/.local/lib/python3.8/site-packages/FlagEmbedding/BGE_M3/modeling.py:335: FutureWarning: You are using `torch.load` with `weights_only=False` (the current default value), which uses the default pickle module implicitly. It is possible to construct malicious pickle data which will execute arbitrary code during unpickling (See https://github.com/pytorch/pytorch/blob/main/SECURITY.md#untrusted-models for more details). In a future release, the default value for `weights_only` will be flipped to `True`. This limits the functions that could be executed during unpickling. Arbitrary objects will no longer be allowed to be loaded via this mode unless they are explicitly allowlisted by the user via `torch.serialization.add_safe_globals`. We recommend you start setting `weights_only=True` for any use case where you don't have full control of the loaded file. Please open an issue on GitHub for any issues related to this experimental feature.
  colbert_state_dict = torch.load(os.path

In [15]:
# Import the required package
import numpy as np

# Set the embedding configurations
EMBEDDING_BATCH_SIZE = 16
embeddings_path = Path("chunk_embeddings.npy")
sparse_weights_path = Path("chunk_sparse_weights.json")
progress_path = Path("embedding_progress.json")

# Embed the full corpus and save the progress
if embeddings_path.exists() and sparse_weights_path.exists() and progress_path.exists():
    all_embeddings = np.load(embeddings_path)
    with open(sparse_weights_path, "r") as f:
        all_sparse_weights = json.load(f)

    # If there was some embeddings completed, resume from the previous run
    with open(progress_path, "r") as f:
        processed_count = json.load(f)["processed_count"]
    print(f"Resuming -- {processed_count} chunks already embedded.")
else:
    all_embeddings = np.zeros((0, test_dense.shape[1]), dtype=np.float32)
    all_sparse_weights = {}
    processed_count = 0

# Print the embedding progress
remaining_chunks = all_chunks[processed_count:]
print(f"Embedding {len(remaining_chunks)} remaining chunks (of {len(all_chunks)} total)...")

#  Create a batch then encode the batch, generating both dense and sparse output in a single forward pass
for batch_start in range(0, len(remaining_chunks), EMBEDDING_BATCH_SIZE):
    batch = remaining_chunks[batch_start:batch_start + EMBEDDING_BATCH_SIZE]
    batch_texts = [c["text"] for c in batch]

    output = embed_model.encode(
        batch_texts, batch_size = EMBEDDING_BATCH_SIZE,
        max_length = CHUNK_SIZE_TOKENS + CHUNK_OVERLAP_TOKENS,
        return_dense = True, return_sparse = True, return_colbert_vecs = False,)
    
    batch_dense = output["dense_vecs"]
    batch_sparse = output["lexical_weights"]

    all_embeddings = np.vstack([all_embeddings, batch_dense])

    # Store each chunk's sparse weights with its ID
    for chunk, sparse_w in zip(batch, batch_sparse):
        all_sparse_weights[chunk["chunk_id"]] = {str(k): float(v) for k, v in sparse_w.items()}

    processed_count += len(batch)

     # Creae a checkpoint every 10 batches, save embeddings, sparse weights, and progress
    if (batch_start // EMBEDDING_BATCH_SIZE) % 10 == 0:
        np.save(embeddings_path, all_embeddings)
        with open(sparse_weights_path, "w") as f:
            json.dump(all_sparse_weights, f)
        with open(progress_path, "w") as f:
            json.dump({"processed_count": processed_count}, f)
        print(f"  Checkpoint: {processed_count}/{len(all_chunks)} chunks embedded")

# Final save once all chunks are processed
np.save(embeddings_path, all_embeddings)
with open(sparse_weights_path, "w") as f:
    json.dump(all_sparse_weights, f)
with open(progress_path, "w") as f:
    json.dump({"processed_count": processed_count}, f)

# Print the embeddings shape when completed
print(f"\nCompleted. Dense embeddings shape: {all_embeddings.shape}, sparse weights for {len(all_sparse_weights)} chunks.")

Resuming -- 44992 chunks already embedded.
Embedding 48147 remaining chunks (of 93139 total)...
  Checkpoint: 45008/93139 chunks embedded
  Checkpoint: 45168/93139 chunks embedded
  Checkpoint: 45328/93139 chunks embedded
  Checkpoint: 45488/93139 chunks embedded
  Checkpoint: 45648/93139 chunks embedded
  Checkpoint: 45808/93139 chunks embedded
  Checkpoint: 45968/93139 chunks embedded
  Checkpoint: 46128/93139 chunks embedded
  Checkpoint: 46288/93139 chunks embedded
  Checkpoint: 46448/93139 chunks embedded
  Checkpoint: 46608/93139 chunks embedded
  Checkpoint: 46768/93139 chunks embedded
  Checkpoint: 46928/93139 chunks embedded
  Checkpoint: 47088/93139 chunks embedded
  Checkpoint: 47248/93139 chunks embedded
  Checkpoint: 47408/93139 chunks embedded
  Checkpoint: 47568/93139 chunks embedded
  Checkpoint: 47728/93139 chunks embedded
  Checkpoint: 47888/93139 chunks embedded
  Checkpoint: 48048/93139 chunks embedded
  Checkpoint: 48208/93139 chunks embedded
  Checkpoint: 48368/93

## Create the vector store with ChromaDB

In [23]:
# Import the required packages
import sys
import pysqlite3
sys.modules["sqlite3"] = sys.modules["pysqlite3"]
import chromadb

In [16]:
# Create the knowledge base store
chroma_client = chromadb.PersistentClient(path = "./chroma_knowledge_base")

# Create the exchange collection
collection = chroma_client.get_or_create_collection(
    name = "caribbean_exchanges_kb",
    metadata = {"hnsw:space": "cosine"},)

# Set the batch size
BATCH_SIZE = 100

# Add chunks to the knowledge base with their IDs and metadata
for i in range(0, len(all_chunks), BATCH_SIZE):
    batch_chunks = all_chunks[i:i + BATCH_SIZE]
    batch_embeddings = all_embeddings[i:i + BATCH_SIZE]
    collection.add(
        ids=[c["chunk_id"] for c in batch_chunks],
        embeddings = batch_embeddings.tolist(),
        documents = [c["text"] for c in batch_chunks],
        metadatas = [{
            "exchange": c["exchange"], "doc_type": c["doc_type"], "title": c["title"] or "",
            "date": str(c["date"]) if c["date"] else "", "company": c["company"] or "",
            "url": c["url"] or "", "retrieved_via": c["retrieved_via"],
        } for c in batch_chunks],)
    
    if (i // BATCH_SIZE) % 10 == 0:
        print(f"  Added {min(i + BATCH_SIZE, len(all_chunks))}/{len(all_chunks)} chunks")

# Print once completed
print(f"\nCompleted. Collection now has {collection.count()} chunks.")

Insert of existing embedding ID: wp-1296893-chunk0
Insert of existing embedding ID: wp-1296859-chunk0
Insert of existing embedding ID: wp-1296803-chunk0
Insert of existing embedding ID: wp-1296956-chunk0
Insert of existing embedding ID: wp-1296942-chunk0
Insert of existing embedding ID: wp-1296953-chunk0
Insert of existing embedding ID: wp-1296947-chunk0
Insert of existing embedding ID: wp-1296944-chunk0
Insert of existing embedding ID: wp-1296935-chunk0
Insert of existing embedding ID: wp-1296930-chunk0
Insert of existing embedding ID: wp-1296847-chunk0
Insert of existing embedding ID: wp-1296914-chunk0
Insert of existing embedding ID: wp-1296853-chunk0
Insert of existing embedding ID: wp-1296916-chunk0
Insert of existing embedding ID: wp-1296901-chunk0
Insert of existing embedding ID: wp-1296884-chunk0
Insert of existing embedding ID: wp-1296899-chunk0
Insert of existing embedding ID: wp-1296862-chunk0
Insert of existing embedding ID: wp-1296883-chunk0
Insert of existing embedding ID

  Added 100/93139 chunks


Insert of existing embedding ID: wp-1296075-chunk0
Insert of existing embedding ID: wp-1296085-chunk0
Insert of existing embedding ID: wp-1296089-chunk0
Insert of existing embedding ID: wp-1296102-chunk0
Insert of existing embedding ID: wp-1296022-chunk0
Insert of existing embedding ID: wp-1296024-chunk0
Insert of existing embedding ID: wp-1295827-chunk0
Insert of existing embedding ID: wp-1296026-chunk0
Insert of existing embedding ID: wp-1296054-chunk0
Insert of existing embedding ID: wp-1296059-chunk0
Insert of existing embedding ID: wp-1296037-chunk0
Insert of existing embedding ID: wp-1296047-chunk0
Insert of existing embedding ID: wp-1296042-chunk0
Insert of existing embedding ID: wp-1296011-chunk0
Insert of existing embedding ID: wp-1295993-chunk0
Insert of existing embedding ID: wp-1296002-chunk0
Insert of existing embedding ID: wp-1296001-chunk0
Insert of existing embedding ID: wp-1296007-chunk0
Insert of existing embedding ID: wp-1295978-chunk0
Insert of existing embedding ID

  Added 1100/93139 chunks


Add of existing embedding ID: wp-1290872-chunk0
Add of existing embedding ID: wp-1290879-chunk0
Add of existing embedding ID: wp-1290785-chunk0
Add of existing embedding ID: wp-1290853-chunk0
Add of existing embedding ID: wp-1290812-chunk0
Add of existing embedding ID: wp-1290814-chunk0
Add of existing embedding ID: wp-1290818-chunk0
Add of existing embedding ID: wp-1290823-chunk0
Add of existing embedding ID: wp-1290844-chunk0
Add of existing embedding ID: wp-1290846-chunk0
Add of existing embedding ID: wp-1290825-chunk0
Add of existing embedding ID: wp-1290849-chunk0
Add of existing embedding ID: wp-1290805-chunk0
Add of existing embedding ID: wp-1290787-chunk0
Add of existing embedding ID: wp-1290781-chunk0
Add of existing embedding ID: wp-1290802-chunk0
Add of existing embedding ID: wp-1290798-chunk0
Add of existing embedding ID: wp-1290770-chunk0
Add of existing embedding ID: wp-1290764-chunk0
Add of existing embedding ID: wp-1290768-chunk0
Add of existing embedding ID: wp-1290745

...

  Added 91100/93139 chunks


Insert of existing embedding ID: ttse-localpdf-1150-chunk61
Insert of existing embedding ID: ttse-localpdf-1150-chunk62
Insert of existing embedding ID: ttse-localpdf-1150-chunk63
Insert of existing embedding ID: ttse-localpdf-1150-chunk64
Insert of existing embedding ID: ttse-localpdf-1150-chunk65
Insert of existing embedding ID: ttse-localpdf-1150-chunk66
Insert of existing embedding ID: ttse-localpdf-1150-chunk67
Insert of existing embedding ID: ttse-localpdf-1150-chunk68
Insert of existing embedding ID: ttse-localpdf-1150-chunk69
Insert of existing embedding ID: ttse-localpdf-1150-chunk70
Insert of existing embedding ID: ttse-localpdf-1150-chunk71
Insert of existing embedding ID: ttse-localpdf-1150-chunk72
Insert of existing embedding ID: ttse-localpdf-1150-chunk73
Insert of existing embedding ID: ttse-localpdf-1150-chunk74
Insert of existing embedding ID: ttse-localpdf-1150-chunk75
Insert of existing embedding ID: ttse-localpdf-1150-chunk76
Insert of existing embedding ID: ttse-lo

  Added 92100/93139 chunks


Add of existing embedding ID: ttse-localpdf-1183-chunk85
Add of existing embedding ID: ttse-localpdf-1183-chunk86
Add of existing embedding ID: ttse-localpdf-1183-chunk87
Add of existing embedding ID: ttse-localpdf-1183-chunk88
Add of existing embedding ID: ttse-localpdf-1183-chunk89
Add of existing embedding ID: ttse-localpdf-1183-chunk90
Add of existing embedding ID: ttse-localpdf-1183-chunk91
Add of existing embedding ID: ttse-localpdf-1183-chunk92
Add of existing embedding ID: ttse-localpdf-1183-chunk93
Add of existing embedding ID: ttse-localpdf-1183-chunk94
Add of existing embedding ID: ttse-localpdf-1183-chunk95
Add of existing embedding ID: ttse-localpdf-1183-chunk96
Add of existing embedding ID: ttse-localpdf-1183-chunk97
Add of existing embedding ID: ttse-localpdf-1183-chunk98
Add of existing embedding ID: ttse-localpdf-1183-chunk99
Add of existing embedding ID: ttse-localpdf-1183-chunk100
Add of existing embedding ID: ttse-localpdf-1183-chunk101
Add of existing embedding ID:

  Added 93100/93139 chunks

Completed. Collection now has 93139 chunks.


## Create a knowlegde base manifest for reproducibility

In [17]:
# Create the knowledge base manifest
manifest = {
    "total_chunks": len(all_chunks),
    "total_source_documents": len(deduped_records),
    "chunk_size_tokens": CHUNK_SIZE_TOKENS,
    "chunk_overlap_tokens": CHUNK_OVERLAP_TOKENS,
    "embedding_model": "BAAI/BGE-M3 (dense + sparse lexical weights)",
    "retrieval_strategy": "Hybrid: Chroma dense ANN candidate retrieval + BGE-M3 sparse lexical rerank",
    "vector_store": "ChromaDB (dense), JSON sidecar (sparse weights), persisted at ./chroma_knowledge_base",
    "by_exchange": df.groupby("exchange").size().to_dict(),
    "by_doc_type": df.groupby("doc_type").size().to_dict(),
    "by_retrieved_via": df["retrieved_via"].value_counts().to_dict(),}

# Save the manifest
with open("knowledge_base_manifest.json", "w") as f:
    json.dump(manifest, f, indent = 2, default = str)

# Print a summary of the manifest
print(json.dumps(manifest, indent = 2, default = str))

{
  "total_chunks": 93139,
  "total_source_documents": 9603,
  "chunk_size_tokens": 512,
  "chunk_overlap_tokens": 100,
  "embedding_model": "BAAI/bge-m3 (dense + sparse lexical weights; ColBERT multi-vector not used)",
  "retrieval_strategy": "Hybrid: Chroma dense ANN candidate retrieval + BGE-M3 sparse lexical rerank",
  "vector_store": "ChromaDB (dense), JSON sidecar (sparse weights), persisted at ./chroma_knowledge_base",
  "by_exchange": {
    "bse": 239,
    "jse": 8216,
    "ttse": 1148
  },
  "by_doc_type": {
    "annual_report_or_financials": 3377,
    "disclosure": 5078,
    "general_document": 1148
  },
  "by_retrieved_via": {
    "wp_api": 5078,
    "direct": 3894,
    "cloud_ocr": 631
  }
}
